<a href="https://colab.research.google.com/github/cristofermaicon1-svg/Siteteste/blob/main/Sintralog.ipynb" target="_parent"><img src="https://colab.research.google.com/assets/colab-badge.svg" alt="Open In Colab"/></a>

In [ ]:
!pip install geobr


In [ ]:
import geobr
import base64
from IPython.display import HTML, display

print("A descarregar os dados e a gerar o mapa...")
rs = geobr.read_municipality(code_muni="RS", year=2020)
geojson_data = rs.to_json()

# O HTML é um texto normal (sem f-string), então não precisa duplicar as chaves {{ }}.
# Só o GeoJSON é injetado no final, no lugar de __GEOJSON__.
HTML_TEMPLATE = r"""
<!DOCTYPE html>
<html lang="pt-BR">
<head>
<meta charset="utf-8">
<title>Sintralog</title>
<link rel="stylesheet" href="https://unpkg.com/leaflet@1.9.4/dist/leaflet.css" />
<style>
  html, body { margin:0; padding:0; height:100%; font-family:'Segoe UI', Arial, sans-serif; background:#f8fafc; }
  .map-wrapper { display:flex; width:100%; height:100%; }
  #map { width:68%; height:100%; }
  #sidebar { width:32%; height:100%; padding:20px; box-sizing:border-box; background:#fff;
             border-left:2px solid #e2e8f0; overflow-y:auto; box-shadow:-2px 0 10px rgba(0,0,0,.05); }
  h3 { margin:0 0 15px; font-size:1.2rem; color:#2d3748; border-bottom:2px solid #edf2f7; padding-bottom:10px; }
  .action-buttons { display:flex; flex-direction:column; gap:8px; margin-bottom:20px; padding-bottom:20px; border-bottom:2px solid #edf2f7; }

  .btn { background:#319795; color:#fff; border:none; padding:9px; border-radius:6px; cursor:pointer;
         font-weight:bold; text-align:center; font-size:13px; }
  .btn:hover { background:#2c7a7b; }
  .btn-danger { background:#e53e3e; } .btn-danger:hover { background:#c53030; }
  .btn-export { background:#4299e1; } .btn-export:hover { background:#3182ce; }
  .btn-import { background:#48bb78; display:block; } .btn-import:hover { background:#38a169; }
  .btn-small { padding:4px 8px; font-size:12px; }

  /* Legenda editável */
  .legend-group { margin-bottom:12px; padding:10px; background:#f7fafc; border:1px solid #e2e8f0; border-radius:8px; }
  .legend-header { display:flex; align-items:center; gap:8px; margin-bottom:8px; }
  .legend-header input[type="color"] { width:36px; height:32px; padding:0; border:1px solid #cbd5e0; border-radius:4px; cursor:pointer; flex-shrink:0; }
  .legend-header input[type="text"] { flex:1; min-width:0; padding:6px 8px; border:1px solid #cbd5e0; border-radius:4px; font-size:14px; font-weight:bold; color:#2d3748; }
  .legend-cities { font-size:.85rem; color:#4a5568; line-height:1.6; }
  .btn-toggle { background:none; border:1px solid #cbd5e0; color:#718096; border-radius:4px;
                width:28px; height:28px; flex-shrink:0; cursor:pointer; font-size:12px; }
  .btn-toggle:hover { background:#edf2f7; }
  .legend-group.recolhido .legend-cities { display:none; }
  .empty { color:#a0aec0; font-size:.9rem; }

  /* Nomes das cidades no mapa (aparecem com zoom) */
  .rotulo-cidade { background:none; border:none; white-space:nowrap; text-align:center; pointer-events:none;
                   font-size:11px; font-weight:600; color:#1a202c;
                   text-shadow:-1px -1px 0 #fff, 1px -1px 0 #fff, -1px 1px 0 #fff, 1px 1px 0 #fff; }

  /* Popup */
  .popup-form { display:flex; flex-direction:column; gap:8px; min-width:200px; }
  .popup-form label { font-size:11px; font-weight:bold; color:#4a5568; margin-bottom:-4px; }
  .popup-form select, .popup-form input[type="text"] { padding:7px; border:1px solid #cbd5e0; border-radius:4px; font-size:13px; }
  .popup-form input[type="color"] { width:100%; height:34px; border:1px solid #cbd5e0; border-radius:4px; cursor:pointer; }
  #novo-grupo { display:none; flex-direction:column; gap:8px; padding:8px; background:#f7fafc; border-radius:6px; }
</style>
</head>
<body>
<div class="map-wrapper">
  <div id="map"></div>
  <div id="sidebar">
    <h3>Controles do Mapa</h3>
    <div class="action-buttons">
      <button class="btn btn-export" onclick="exportarJSON()">📥 Exportar Dados (JSON)</button>
      <label class="btn btn-import">📤 Importar Dados (JSON)
        <input type="file" accept=".json" style="display:none" onchange="importarJSON(event)">
      </label>
    </div>

    <h3>Legenda</h3>
    <button class="btn" style="width:100%; margin-bottom:12px" onclick="novoGrupoVazio()">➕ Novo grupo</button>
    <div id="legend"></div>
  </div>
</div>

<script src="https://unpkg.com/leaflet@1.9.4/dist/leaflet.js"></script>
<script>
  const geojsonData = __GEOJSON__;

  // ---------- Estado ----------
  // grupos:  { id: { color, label } }
  // cidades: { nomeCidade: idDoGrupo }
  let grupos = {};
  let cidades = {};
  let proximoId = 1;
  let gruposRecolhidos = {};   // { id: true } quando a lista de cidades está oculta
  let cidadeAtual = null;
  const PALETA = ['#319795','#e53e3e','#3182ce','#d69e2e','#805ad5','#dd6b20','#38a169','#d53f8c'];
  const COR_VAZIA = '#cbd5e0';

  function esc(s) { return String(s).replace(/&/g,'&amp;').replace(/</g,'&lt;').replace(/"/g,'&quot;'); }

  function criarGrupo(color, label) {
    const id = 'g' + (proximoId++);
    grupos[id] = { color: color, label: label };
    return id;
  }
  function corPadraoNova() { return PALETA[Object.keys(grupos).length % PALETA.length]; }

  // ---------- Mapa ----------
  const map = L.map('map').setView([-30.0346, -53.2177], 7);
  // Fundo cinza claro da Esri: gratuito e sem chave de API.
  // (Se preferir sem fundo nenhum, apague esta linha: os municípios continuam aparecendo.)
  L.tileLayer('https://server.arcgisonline.com/ArcGIS/rest/services/Canvas/World_Light_Gray_Base/MapServer/tile/{z}/{y}/{x}', {
    attribution: 'Tiles &copy; Esri', maxZoom: 13
  }).addTo(map);
  setTimeout(() => map.invalidateSize(), 300);

  function estiloDe(nome) {
    const g = grupos[cidades[nome]];
    return g ? { fillColor: g.color, weight:1, opacity:1, color:'#fff', fillOpacity:.85 }
             : { fillColor: COR_VAZIA, weight:1, opacity:1, color:'#fff', fillOpacity:.7 };
  }
  function repintar() {
    geojsonLayer.eachLayer(l => l.setStyle(estiloDe(l.feature.properties.name_muni)));
  }

  const geojsonLayer = L.geoJSON(geojsonData, {
    style: f => estiloDe(f.properties.name_muni),
    onEachFeature: function(feature, layer) {
      const nome = feature.properties.name_muni;
      layer.bindTooltip(nome, { sticky: true });
      layer.on('click', function() {
        cidadeAtual = nome;
        layer.bindPopup(montarPopup(nome)).openPopup();
      });
    }
  }).addTo(map);

  // ---------- Nomes sobre as cidades (só a partir de certo zoom) ----------
  const ZOOM_ROTULOS = 9;   // aumente para mostrar os nomes só com mais zoom
  const camadaRotulos = L.layerGroup().addTo(map);
  const centros = {};       // cache do centro de cada município
  geojsonLayer.eachLayer(l => { centros[l.feature.properties.name_muni] = l.getBounds().getCenter(); });

  function atualizarRotulos() {
    camadaRotulos.clearLayers();
    if (map.getZoom() < ZOOM_ROTULOS) return;
    const vis = map.getBounds();
    Object.keys(centros).forEach(nome => {
      if (!vis.contains(centros[nome])) return;   // só desenha o que está na tela
      L.marker(centros[nome], {
        interactive: false,
        icon: L.divIcon({ className: 'rotulo-cidade', html: esc(nome), iconSize: [0, 0] })
      }).addTo(camadaRotulos);
    });
  }
  map.on('zoomend moveend', atualizarRotulos);

  // ---------- Popup: escolher um grupo existente (ou criar um novo) ----------
  function montarPopup(nome) {
    const ids = Object.keys(grupos);
    const atual = cidades[nome];
    let opcoes = ids.map(id =>
      `<option value="${id}" ${id === atual ? 'selected' : ''}>${esc(grupos[id].label || 'Sem nome')}</option>`).join('');
    opcoes += `<option value="__novo__" ${ids.length === 0 ? 'selected' : ''}>➕ Novo grupo...</option>`;

    return `
      <div class="popup-form">
        <h4 style="margin:0;color:#2d3748;font-size:14px">${esc(nome)}</h4>
        <label>Grupo:</label>
        <select id="pop-sel" onchange="alternarNovo()">${opcoes}</select>
        <div id="novo-grupo">
          <label>Nome do novo grupo:</label>
          <input type="text" id="pop-rot" value="Cidade visitada">
          <label>Cor:</label>
          <input type="color" id="pop-cor" value="${corPadraoNova()}">
        </div>
        <button class="btn" onclick="aplicarNaCidade()">Aplicar</button>
        ${atual ? `<button class="btn btn-danger" onclick="removerDaCidade()">Remover da legenda</button>` : ''}
      </div>`;
  }
  window.alternarNovo = function() {
    const sel = document.getElementById('pop-sel');
    document.getElementById('novo-grupo').style.display = sel.value === '__novo__' ? 'flex' : 'none';
  };
  // abre o popup já mostrando o bloco "novo grupo" quando ainda não há grupos
  map.on('popupopen', () => { if (document.getElementById('pop-sel')) alternarNovo(); });

  window.aplicarNaCidade = function() {
    let id = document.getElementById('pop-sel').value;
    if (id === '__novo__') {
      id = criarGrupo(document.getElementById('pop-cor').value,
                      document.getElementById('pop-rot').value.trim() || 'Novo grupo');
    }
    cidades[cidadeAtual] = id;
    map.closePopup(); repintar(); renderLegenda();
  };
  window.removerDaCidade = function() {
    delete cidades[cidadeAtual];
    map.closePopup(); repintar(); renderLegenda();
  };

  // ---------- Legenda totalmente editável ----------
  function renderLegenda() {
    const div = document.getElementById('legend');
    const ids = Object.keys(grupos);
    if (ids.length === 0) {
      div.innerHTML = '<p class="empty">Nenhum grupo ainda. Clique numa cidade no mapa ou em "Novo grupo".</p>';
      return;
    }
    div.innerHTML = ids.map(id => {
      const nomes = Object.keys(cidades).filter(c => cidades[c] === id).sort((a, b) => a.localeCompare(b, 'pt-BR'));
      const chips = nomes.length
        ? esc(nomes.join(', '))
        : '<span class="empty">Nenhuma cidade neste grupo</span>';
      const recolhido = gruposRecolhidos[id] ? ' recolhido' : '';
      return `
        <div class="legend-group${recolhido}">
          <div class="legend-header">
            <input type="color" value="${grupos[id].color}" oninput="mudarCor('${id}', this.value)" title="Mudar a cor do grupo">
            <input type="text" value="${esc(grupos[id].label)}" onchange="mudarNome('${id}', this.value)" title="Editar o nome do grupo">
            <button class="btn-toggle" title="Mostrar/ocultar cidades" onclick="alternarRecolhido('${id}')">${gruposRecolhidos[id] ? '▸' : '▾'}</button>
            <button class="btn btn-danger btn-small" title="Apagar grupo" onclick="apagarGrupo('${id}')">🗑</button>
          </div>
          <div class="legend-cities">${chips}</div>
        </div>`;
    }).join('');
  }

  // Não re-renderiza a legenda enquanto digita/escolhe cor (evita perder o foco)
  window.mudarCor = function(id, cor) { grupos[id].color = cor; repintar(); };
  window.mudarNome = function(id, nome) { grupos[id].label = nome.trim() || 'Sem nome'; };
  window.alternarRecolhido = function(id) {
    gruposRecolhidos[id] = !gruposRecolhidos[id];
    renderLegenda();
  };
  window.apagarGrupo = function(id) {
    const qtd = Object.values(cidades).filter(g => g === id).length;
    if (qtd > 0 && !confirm(`Apagar o grupo "${grupos[id].label}" e tirar ${qtd} cidade(s) dele?`)) return;
    Object.keys(cidades).forEach(c => { if (cidades[c] === id) delete cidades[c]; });
    delete grupos[id];
    repintar(); renderLegenda();
  };
  window.novoGrupoVazio = function() {
    criarGrupo(corPadraoNova(), 'Novo grupo');
    renderLegenda();
  };

  // ---------- Exportar / Importar ----------
  window.exportarJSON = function() {
    if (Object.keys(grupos).length === 0) { alert('Não há nada para exportar!'); return; }
    const dados = { versao: 2, grupos: grupos, cidades: cidades };
    const a = document.createElement('a');
    a.href = 'data:text/json;charset=utf-8,' + encodeURIComponent(JSON.stringify(dados, null, 2));
    a.download = 'meu_mapa_rs.json';
    document.body.appendChild(a); a.click(); a.remove();
  };

  window.importarJSON = function(event) {
    const file = event.target.files[0];
    if (!file) return;
    const reader = new FileReader();
    reader.onload = function(e) {
      try {
        const dados = JSON.parse(e.target.result);
        grupos = {}; cidades = {}; proximoId = 1;

        if (dados.grupos && dados.cidades) {
          // Formato novo
          grupos = dados.grupos; cidades = dados.cidades;
          proximoId = Math.max(0, ...Object.keys(grupos).map(k => parseInt(k.replace('g',''), 10) || 0)) + 1;
        } else {
          // Formato antigo { cidade: {color, label} } -> converte em grupos automaticamente
          const porChave = {};
          Object.keys(dados).forEach(cidade => {
            const it = dados[cidade];
            const k = it.color + '|' + it.label;
            if (!porChave[k]) porChave[k] = criarGrupo(it.color, it.label || 'Sem nome');
            cidades[cidade] = porChave[k];
          });
        }
        repintar(); renderLegenda();
        alert('Mapa carregado com sucesso!');
      } catch (err) {
        alert('Erro ao ler o arquivo JSON. Verifique se é o arquivo correto.');
      }
      event.target.value = '';
    };
    reader.readAsText(file);
  };

  renderLegenda();
</script>
</body>
</html>
"""

html_code = HTML_TEMPLATE.replace("__GEOJSON__", geojson_data)

# Salvar e gerar visualização
with open("mapa_interativo_rs.html", "w", encoding="utf-8") as f:
    f.write(html_code)

b64_html = base64.b64encode(html_code.encode("utf-8")).decode("utf-8")

display_html = f"""
<div>
    <button id="btn-abrir-mapa" style="
        margin-bottom: 12px; padding: 12px 20px; background-color: #2b6cb0; color: white;
        border: none; cursor: pointer; font-family: Arial, sans-serif; font-size: 14px;
        font-weight: bold; border-radius: 6px; box-shadow: 0 2px 4px rgba(0,0,0,0.2);
    ">&#128279; Abrir Mapa em Nova Aba (Recomendado)</button>
    <script>
        document.getElementById('btn-abrir-mapa').onclick = function() {{
            const b64 = "{b64_html}";
            const bytes = Uint8Array.from(atob(b64), c => c.charCodeAt(0));
            const blob = new Blob([bytes], {{type: 'text/html;charset=utf-8'}});
            window.open(URL.createObjectURL(blob), '_blank');
        }};
    </script>
</div>
<iframe src="data:text/html;base64,{b64_html}" width="100%" height="600px" style="border: 1px solid #cbd5e0; border-radius: 8px;"></iframe>
"""

display(HTML(display_html))
print("\nConcluído! O arquivo mapa_interativo_rs.html também foi salvo.")

A descarregar os dados e a gerar o mapa...


municipalities_2020_simplified.parquet: 100%|██████████| 20.2M/20.2M [00:00<00:00, 135MB/s] 



Concluído! O arquivo mapa_interativo_rs.html também foi salvo.
